# Ground truth datasets exploration notebook

**Description**

This notebook is used for **exploring five ground truth datasets** (four dataset are polygons/multi-polygons and one dataset is point) and compare how each dataset complement each other to decide which datasets will be used to create a single ground truth of public urban green spaces (PUGS) in Dresden.

**Overview of datasets**

| Data source     | Geometry type     | Dataset name     | Description      |
|-----------------|-------------------|------------------|------------------|
|  Copernicus Land Monitoring Service | Polygon/Multi-polygon | European Urban Atlas (EUA) dataset <br> (Reclassified dataset) <br><br> (Temporal extent of dataset: 2017-2019)| This dataset is pre-processed from [Urban Atlas Land Cover/Land use 2018](https://land.copernicus.eu/en/products/urban-atlas/urban-atlas-2018) which provide land cover and land use data in Functional Urban Areas (FUA) in Europe and UK. The dataset consists of 17 urban classes with the Minimum Mapping Unit (MMU) of 0.25 ha and for 10 rural classes with the MMU of 1 ha. The *Green urban areas, Forests, and Herbaceous vegetation association class* are reclassiied to PUGS. <br><br>**Note:** this dataset is updated every 6 years. |
| Dresden Open Data Portal  <br> (Origin from Office for Urban Green Spaces and Waste Management) | Polygon/Multi-polygon | [Park- und Grünanlagen (Flächen)](https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=751&RenderHint=TargetHTML) <br> (Park and green spaces)  <br><br> (Last update: 2020) | Provide the areas of parks and green spaces within Dresden. It includes **only green spaces that are under the administration of the state capital Dresden**. The dataset includes the areas that fall into: <br> • I1 - parks <br> • F41 - Green city square (Begrünte Stadtplätze) <br> • F43 - Other green and open spaces (Sonstige Grün- und Freiflächen) <br><br> [More details of each category](https://kommisdd.dresden.de/net3/public/ogcsl.ashx?Service=IKX&Request=GetBlobData&ts=638522102964126790&StObjectDataId=31389&ikxStoreId=) |
| Dresden Open Data Portal  <br> (Origin from Office for Geodata and Cadastre) | Polygon/Multi-polygon | [Grün- und Freiflächen](https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=1638&RenderHint=TargetHTML) <br> (Green and open spaces) <br><br> (Last update: 2024) | Provide the areas of green and open spaces in Dresden. The dataset only includes the areas that fall into: <br> • F - Green and open spaces (Grün- und Freifläche) <br> • K - Cemeteries (Friedhöfe) <br> • L - Forest/Woodland (Wald / Gehölz) <br><br> [More details of each category](https://kommisdd.dresden.de/net3/public/ogcsl.ashx?Service=IKX&Request=GetBlobData&ts=638522102964126790&StObjectDataId=31389&ikxStoreId=) |
| Dresden Open Data Portal <br> (Origin from Environment Agency) | Polygon/Multi-polygon | Parks (I type) <br><br> (Last update: 2021) | Provide the areas according to different types of land uses. This dataset contains only “I1 - Parks, Zoo, Botanical Garden type” from [Nutzungsarten (Strukturtypen) – Kartierung](https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=1059&RenderHint=TargetHTML) <br> (Types of use - structure types - Mapping) dataset. <br><br> [More details of each category](https://kommisdd.dresden.de/net3/public/ogcsl.ashx?Service=IKX&Request=GetBlobData&ts=638522102964126790&StObjectDataId=31389&ikxStoreId=) <br> More details on preprocessing can be found in `2_data_processing_ground_truth.ipynb` |
| Dresden Open Data Portal <br> (Origin from Environment Agency) | Point | [Parkanlagen, Gärten](https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=138&RenderHint=TargetHTML) (Parks, gardens) <br><br> (Last update: 2021) | Provide the location of all parks and park-like gardens within the urban area of Dresden. This dataset contains not only parks that are under the administration of the state capital Dresden but also parks under other organizations. <br><br> [More details](https://www.dresden.de/de/stadtraum/umwelt/gruenes-dresden/gruenanlagen-parks.php) |

**Input file(s)**

5 files
- Green and Open spaces dataset (`green_and_openspaces_dataset.geojson`)
- Parks and Green spaces dataset (`parks_and_greenspaces_dataset.geojson`)
- Parks (I type) dataset (`i_parks_type_dataset.geojson`)
- Parks point dataset (`point_parks_and_gardens_dataset.geojson`)
- EUA dataset (Reclassified) (`eua_pugs_dataset.geojson`)

**Output file(s)**

There is no output file.

**Requirements/Dependencies**

This notebook requires user to run the following notebooks first:
- 1_data_acquisition_osm.ipynb
- 1_data_acquisition_ground_truth.ipynb
- 1_data_acquisition_satellite_image.ipynb
- 2_data_processing_osm.ipynb
- 2_data_processing_ground_truth.ipynb
- 3_data_processing_satellite_image.ipynb

In case all the input data required in this notebook are available, user can directly run this notebook without running the notebooks in the list.

# 1. Import libraries and load config

It can take up to 5-6 mins to complete this section.

In [1]:
import os
import sys

# Add the root directory to Python path so that we can import the modules
root_dir = os.path.abspath(os.path.join(os.getcwd(), ".."))
sys.path.append(root_dir)

In [2]:
import geopandas as gpd
import yaml
from pugs_detection.utils import (
    print_basic_info,
)
from pugs_detection.ground_truth import (
    find_overlap_area,
    calculate_dataset_overlap,
    calculate_category_overlap,
    check_intersecting_point,
    add_ndvi_to_polygons,
    merge_datasets,
    print_non_green_space_info,
)
from pugs_detection.plots import visualize_map

In [3]:
# Load config
with open("../config.yaml", "r") as f:
    config = yaml.safe_load(f)

# 2. Import data

## Green and open spaces

Dataset name: Grün- und Freiflächen 

Link to data: https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=1638&RenderHint=TargetHTML

### Read data

In [4]:
input_file_path = config["paths"]["green_openspaces_path"]

In [5]:
green_os_dataset = gpd.read_file(input_file_path)

In [6]:
print_basic_info(green_os_dataset)

Number of rows: 3024
Number of columns: 13


,blocknr,obj_id,kattime_brutto,sst_liste,sst_lv_2_liste,sst_lv_3_liste,deskn1_liste,desk2,desk3,deskn1,flaeche,aend,geometry
0,852300,21098a,919611,L Wald / Gehölz,L1 Wald nach sächs. Waldgesetz,L11 Wald nach sächs. Waldgesetz,unversiegelt (naturnahe Flächen mit VSG-Grad k...,L1,L11,0.0,15786.025474,02.05.2024 00:00:00,"POLYGON ((407724.344 5652810.146, 407715.219 5..."
1,853120,2079a,886188,F Grün- und Freiflächen,F2 Sonstige Gärten,F21 Klein- und Wochenendgärten,VSG-Grad 10 - 20 %,F2,F21,1.0,70079.538136,10.12.2018 00:00:00,"POLYGON ((408031.504 5652172.101, 408032.157 5..."
2,853320,2603a,885095,F Grün- und Freiflächen,F4 Sonstige Grünflächen im urbanen Raum,F41 Begrünte Stadtplätze,VSG-Grad 21 - 40 %,F4,F41,2.0,5079.848742,10.12.2018 00:00:00,"POLYGON ((408056.92 5651983.93, 408085.09 5651..."


## Park and green spaces

Datset name: Park- und Grünanlagen (Flächen)

Link to data: https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=751&RenderHint=TargetHTML

### Read data

In [7]:
input_file_path = config["paths"]["parks_greenspaces_path"]

In [8]:
park_greenspace_dataset = gpd.read_file(input_file_path)

In [9]:
print_basic_info(park_greenspace_dataset)

Number of rows: 587
Number of columns: 8


,id,oa,ort,groesse,anlage,antrag,bezirk,geometry
0,6067/03,O Schönfeld-Weißig,Straße des Friedens (Pappritz) - zw. Am Dorfte...,348.18,Park- und Grünanlagen,http://www.dresden.de/media/pdf/formulare/Antr...,34,"MULTIPOLYGON (((419624.766 5654422.363, 419621..."
1,0010/04,StB Altstadt,Bürgerwiese - zw. Lennéstraße u. Zoologischen ...,36540.13,Park- und Grünanlagen,http://www.dresden.de/media/pdf/formulare/Antr...,20,"POLYGON ((412242.5 5654910.433, 412238.775 565..."
2,5763/01,StB Prohlis,Reicker Straße - zw. Hans-Jüchser-Straße u. Be...,1105.00,Park- und Grünanlagen,http://www.dresden.de/media/pdf/formulare/Antr...,27,"POLYGON ((414516.005 5652671.438, 414515.96 56..."


## Parks (I type) dataset

Dataset name: Parks (I type) dataset which is originally from Nutzungsarten (Strukturtypen)- Kartierung

This dataset is acquired from Nutzungsarten (Strukturtypen)- Kartierung dataset. The data is downloaded from WFS and only select areas in **I type**.

Link to data: https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=1059&RenderHint=TargetHTML

In [10]:
input_file_path = config["paths"]["parks_i_type_path"]

In [11]:
park_i_type_dataset = gpd.read_file(input_file_path)

In [12]:
print_basic_info(park_i_type_dataset)

Number of rows: 89
Number of columns: 15


,gml_id,blocknr,obj_id,kattime_brutto,kattime,sst_liste,sst_lv_2_liste,sst_lv_3_liste,deskn1_liste,desk2,desk3,deskn1,flaeche,aend,geometry
0,L1263.919778,945120,21088a,895546,919778,"I Parkanlagen, Zoo, Botanischer Garten",I1 Parks,I11 Parks,VSG-Grad 10 - 20 %,I1,I11,1,6047.863237,2024-04-24,"POLYGON ((408818.015 5653833.579, 408807.323 5..."
1,L1263.916183,933210,5578a,891283,916183,"I Parkanlagen, Zoo, Botanischer Garten",I1 Parks,I11 Parks,unversiegelt (naturnahe Flächen mit VSG-Grad k...,I1,I11,0,16330.601040,2018-12-10,"POLYGON ((408887.478 5653977.017, 408887.281 5..."
2,L1263.910452,036070,130a,891992,910452,"I Parkanlagen, Zoo, Botanischer Garten",I1 Parks,I11 Parks,VSG-Grad 10 - 20 %,I1,I11,1,18189.652296,2022-05-20,"POLYGON ((412210.427 5655508.714, 412258.965 5..."


## Parks, gardens (point)

Dataset name: Parkanlagen, Gärten

Link to data: https://kommisdd.dresden.de/net3/public/ogc.ashx?Service=IKX&NodeId=138&RenderHint=TargetHTML

It contains other parks that is not under municipality as well (unlike the polygon that contains only areas under the administration of the state capital Dresden based on what I understand)

More detail: https://www.dresden.de/de/stadtraum/umwelt/gruenes-dresden/gruenanlagen-parks.php

In [13]:
input_file_path = config["paths"]["point_parks_path"]

In [14]:
point_park_garden_dataset = gpd.read_file(input_file_path)

In [15]:
print_basic_info(point_park_garden_dataset)

Number of rows: 64
Number of columns: 6


,einrichtung,lage,einrichtungsart,url,ds_modified,geometry
0,Räcknitzer Park,Räcknitzhöhe,Park,de.wikipedia.org/wiki/Volkspark_R%C3%A4cknitz,13.03.2025 13:42:04,POINT (411557.217 5653379.243)
1,Gönnsdorfer Park,Am Park,Park,www.dresden.de/de/stadtraum/umwelt/gruenes-dre...,13.03.2025 15:55:02,POINT (420552.833 5655956.565)
2,Am Hohen Stein,Coschützer Straße,Park,www.dresden.de/de/stadtraum/umwelt/gruenes-dre...,14.03.2025 13:28:14,POINT (409087.775 5653243.08)


## EUA dataset (Reclassified dataset)

Link to original data: https://land.copernicus.eu/en/products/urban-atlas/urban-atlas-2018

In [16]:
input_file_path = config["paths"]["eua_pugs_path"]

In [17]:
eua_pugs_dataset = gpd.read_file(input_file_path)

In [18]:
print_basic_info(eua_pugs_dataset)

Number of rows: 715
Number of columns: 13


,country,fua_name,fua_code,code_2018,class_2018,prod_date,identifier,perimeter,area,comment,Pop2018,new_class,geometry
0,DE,Dresden,DE009L2,31000,Forests,2020-09,61166-DE009L2,8594.180156,755622.324881,None,0,1,"MULTIPOLYGON (((415693.987 5648031.69, 415693...."
1,DE,Dresden,DE009L2,31000,Forests,2020-09,61216-DE009L2,5878.091960,707765.243412,None,0,1,"MULTIPOLYGON (((417530.296 5648197.121, 417532..."
2,DE,Dresden,DE009L2,32000,Herbaceous vegetation associations (natural gr...,2020-09,65095-DE009L2,581.922400,15751.756655,None,0,1,"POLYGON ((415999.441 5648195.733, 415992.508 5..."


# 3. Check overlap and non-overlap area between two datasets from Dresden

Two datasets are 
- Green and open spaces dataset
- Park (I type) dataset

These datasets are checked whether they has the overlapping and non-overlapping area or not and get some insight how they can complement each other.

In [19]:
overlap_green_os_park_itype_dataset = find_overlap_area(
    green_os_dataset, park_i_type_dataset
)
overlap_park_itype_green_os_dataset = find_overlap_area(
    park_i_type_dataset, green_os_dataset
)

## Hypothesis: Parks in the Parks dataset (polygon) don’t overlap with the Open spaces dataset

According to dataset description, 
- **Green and open spaces dataset**: contains areas that fall into F (green and open spaces), K (cemeteries), and L (forest/woodland) category
- **Park (I type) dataset**: contains areas that fall into I (Parks, Zoo, Botanical Garden) category

So both datasets should not overlap.

### Total overlapping area

$$\text{Total overlap percentage in Dataset1} = \frac{\text{Overlap area of Dataset1}}{\text{Total area of Dataset1}} \times 100$$

$$\text{Total overlap percentage in Dataset2} = \frac{\text{Overlap area of Dataset2}}{\text{Total area of Dataset2}} \times 100$$

Note:
- Datset 1 is Park (I type) dataset
- Dataset 2 is Green and open spaces dataset

In [20]:
calculate_dataset_overlap(park_i_type_dataset, green_os_dataset)

Dataset 1 overlap percentage: 0.00%
Dataset 2 overlap percentage: 0.00%


# 4. Merge Green and open spaces and Parks (I type) dataset

Since there is no overlap between these two dataset, two datasets are merged to make the full public urban green space (PUGS) ground truth 

In [21]:
park_i_type_dataset = park_i_type_dataset.rename(
    columns={
        "sst_lv_3_l": "sst_lv_3_liste",
        "sst_lv_2_l": "sst_lv_2_liste",
        "deskn1_lis": "deskn1_liste",
    }
)

In [22]:
# Add data source
green_os_dataset.loc[:, "dataset_source"] = "green and open spaces"
park_i_type_dataset.loc[:, "dataset_source"] = "park (I type)"
# Select columns to keep
selected_cols = [
    "geometry",
    "sst_lv_3_liste",
    "sst_lv_2_liste",
    "deskn1_liste",
    "flaeche",
    "dataset_source",
    "blocknr",
]
# Filter columns
green_os_selected = green_os_dataset[selected_cols]
park_i_type_selected = park_i_type_dataset[selected_cols]

In [23]:
merged_dataset = merge_datasets(green_os_selected, park_i_type_selected)

In [24]:
print(f"Merged Dresden dataset contains {len(merged_dataset)} features:")
print(
    f"- {len(merged_dataset[merged_dataset['dataset_source'] == 'green and open spaces'])} from Green Open Spaces"
)
print(
    f"- {len(merged_dataset[merged_dataset['dataset_source'] == 'park (I type)'])} from Park (I type)"
)

Merged Dresden dataset contains 3113 features:
- 3024 from Green Open Spaces
- 89 from Park (I type)


In [25]:
gdf_list = [merged_dataset]
column_list = ["dataset_source"]
tooltip_list = [["sst_lv_3_liste", "area", "flaeche"]]
name_list = ["Merged Dataset"]

In [26]:
map_viz = visualize_map(
    gdf_list=gdf_list,
    column_list=column_list,
    name_list=name_list,
    tooltip_list=tooltip_list,
)

map_viz

# 5. Check overlap and non-overlap area between merged datasets and Park and green spaces dataset

Two datasets are 
- Merged dataset
- Park and green spaces dataset

These datasets are checked whether they has the overlapping and non-overlapping area or not and get some insight how they can complement each other.

In [27]:
overlap_merged_park_gs_dataset = find_overlap_area(
    merged_dataset, park_greenspace_dataset
)
overlap_park_greenspace_merged_dataset = find_overlap_area(
    park_greenspace_dataset, merged_dataset
)

- Dataset 1 is Park and green spaces dataset
- Dataset 2 is Merged dataset

In [28]:
calculate_dataset_overlap(park_greenspace_dataset, merged_dataset)

Dataset 1 overlap percentage: 73.39%
Dataset 2 overlap percentage: 1.97%


In [29]:
# gdf_list = [
#     overlap_park_greenspace_merged_dataset[
#         overlap_park_greenspace_merged_dataset["overlap"] == "no"
#     ],
#     overlap_merged_park_gs_dataset[overlap_merged_park_gs_dataset["overlap"] == "no"],
# ]
# name_list = ["Park and Green Spaces", "Merged Dataset"]
# tooltip_list = [
#     ["ort", "overlap_pct", "groesse"],
#     ["sst_lv_3_liste", "overlap_pct", "area"],
# ]
# style_list = [
#     {"color": "blue", "fillColor": "#0000FF", "fillOpacity": 0.6},
#     {"color": "orange", "fillColor": "#ffa500", "fillOpacity": 0.6},
# ]
# tile_list = ["Esri Satellite", "OSM"]

In [30]:
# map_viz = visualize_map(
#     gdf_list=gdf_list,
#     name_list=name_list,
#     tooltip_list=tooltip_list,
#     style_list=style_list,
#     tile_list=tile_list,
# )

# map_viz

# 6. Merge the previous merged dataset and Parks and green spaces dataset

There are still non-overlapping areas, 26.61%, in Parks and green spaces dataset. So it is worth to merge these areas into the final single dataset.

## Filter the areas that are considered as non-public out

As the tasks is for creating the ground truth for Public Urban Green Space (PUGS), so filtering non-public areas out is required. Moreover, to compare the dataset from Dresden Open data portal with EUA dataset, we need only PUGS because reclassified EUA dataset only contains PUGS.

### Filter areas that isn't relevant to public urban green space (PUGS) in Green and open spaces dataset

The sub-types that isn't relevant to PUGS:

Level 2
- F1 Kleingärten (Allotment gardens)
- F2 Sonstige Gärten (Other gardens)
- A1 Wohnbebauung (Residential development)
- F3 Verkehrsbegleitgrün (Roadside greenery)

Level 3
- F42 Begrünte Deponie (Green landfills)

In [31]:
non_pugs_lv2_list = [
    "F1   Kleingärten",
    "F2   Sonstige Gärten",
    "A1   Wohnbebauung",
    "F3   Verkehrsbegleitgrün",
]

non_pugs_lv3_list = ["F42   Begrünte Deponien"]

In [32]:
filtered_merged_dataset = merged_dataset[
    ~merged_dataset["sst_lv_2_liste"].isin(non_pugs_lv2_list)
]

In [33]:
filtered_merged_dataset = filtered_merged_dataset[
    ~filtered_merged_dataset["sst_lv_3_liste"].isin(non_pugs_lv3_list)
]

### Filter zoo out

Zoo isn't considered as public since there is entrance fee so it isn't freely accessible.

In [34]:
filtered_merged_dataset = filtered_merged_dataset[
    filtered_merged_dataset["blocknr"] != "035170"
]

In [35]:
print(
    f"Number of polygons in Green and Open Spaces Dataset before filtering: {len(merged_dataset)}"
)
print(
    f"Number of polygons in Green and Open Spaces Dataset after filtering: {len(filtered_merged_dataset)}"
)

Number of polygons in Green and Open Spaces Dataset before filtering: 3113
Number of polygons in Green and Open Spaces Dataset after filtering: 1595


### Filter areas in Park and green spaces that significantly overlap with sub-types that aren't related to PUGS

In [36]:
significant_overlap_area = overlap_park_greenspace_merged_dataset[
    (overlap_park_greenspace_merged_dataset["overlap_pct"] >= 50)
    & (
        (
            overlap_park_greenspace_merged_dataset["sst_lv_2_liste"].isin(
                non_pugs_lv2_list
            )
        )
        | (
            overlap_park_greenspace_merged_dataset["sst_lv_3_liste"].isin(
                non_pugs_lv3_list
            )
        )
    )
]

In [37]:
significant_overlap_id_list = significant_overlap_area["ort"].unique()

In [38]:
filtered_park_greenspace_dataset = park_greenspace_dataset[
    ~(park_greenspace_dataset["ort"].isin(significant_overlap_id_list))
]

In [39]:
print(
    f"Number of polygons in Park and Green spaces Dataset before filtering: {len(park_greenspace_dataset)}"
)
print(
    f"Number of polygons in Park and Green spaces Dataset after filtering: {len(filtered_park_greenspace_dataset)}"
)

Number of polygons in Park and Green spaces Dataset before filtering: 587
Number of polygons in Park and Green spaces Dataset after filtering: 547


## Merge datasets

In [40]:
# Add data source
filtered_park_greenspace_dataset.loc[:, "dataset_source"] = "park and green spaces"
# Select columns to keep
selected_cols = [
    "geometry",
    "id",
    "ort",
    "groesse",
    "oa",
    "dataset_source",
]
# Filter columns
filtered_park_greenspace_selected = filtered_park_greenspace_dataset[selected_cols]

d:\research_line\PUGS\code_resubmission\pugs-detection\.venv\Lib\site-packages\geopandas\geodataframe.py:1819: SettingWithCopyWarning: 
A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy
  super().__setitem__(key, value)


In [41]:
final_merged_dataset = merge_datasets(
    filtered_merged_dataset, filtered_park_greenspace_selected
)

In [42]:
print(f"Merged Dresden dataset contains {len(final_merged_dataset)} features:")
print(
    f"- {len(final_merged_dataset[final_merged_dataset['dataset_source'] == 'green and open spaces'])} from Green Open Spaces"
)
print(
    f"- {len(final_merged_dataset[final_merged_dataset['dataset_source'] == 'park (I type)'])} from Park (I type)"
)
print(
    f"- {len(final_merged_dataset[final_merged_dataset['dataset_source'] == 'park and green spaces'])} from Parks and Green Spaces"
)

Merged Dresden dataset contains 2142 features:
- 1507 from Green Open Spaces
- 88 from Park (I type)
- 547 from Parks and Green Spaces


Visualize the merged dataset (color indicates the data source)

In [43]:
gdf_list = [final_merged_dataset]
column_list = ["dataset_source"]
tooltip_list = [["sst_lv_3_liste", "area", "flaeche"]]
name_list = ["Final Merged Dataset"]

In [44]:
map_viz = visualize_map(
    gdf_list=gdf_list,
    column_list=column_list,
    name_list=name_list,
    tooltip_list=tooltip_list,
)

map_viz

# 7. Crosscheck Merged dataset with Parks, gardens (point dataset)

## Check the total points that intersect with Merged dataset

### Filter zoo out

Zoo isn't considered as public since there is entrance fee so it isn't freely accessible.

In [45]:
point_park_garden_dataset = point_park_garden_dataset[
    ~point_park_garden_dataset["einrichtung"].str.contains("zoo", case=False)
]

## Intersect the point with merged dataset

In [46]:
point_intersect_merged_dataset = check_intersecting_point(
    point_park_garden_dataset, final_merged_dataset, buffer_distance=60
)

Points intersecting with dataset: 60 out of 63 (95.24%)


In [47]:
point_intersect_dresden_dataset = point_intersect_merged_dataset.rename(
    columns={
        "index_right": "greenspace_index",
    }
)

In [48]:
dresden_area_intersect_point = final_merged_dataset.sjoin(
    point_intersect_dresden_dataset, how="inner", predicate="intersects"
)

dresden_area_intersect_point = dresden_area_intersect_point.drop_duplicates(
    subset=["greenspace_index"]
)

dresden_area_intersect_point = dresden_area_intersect_point.drop(
    columns=[
        "url",
        "ds_modified",
        "greenspace_index",
        "sst_lv_3_liste_right",
        "sst_lv_2_liste_right",
        "deskn1_liste_right",
        "flaeche_right",
        "dataset_source_right",
        "area_right",
    ]
)

In [49]:
gdf_list = [dresden_area_intersect_point, point_park_garden_dataset]
marker_style = [{}, {"radius": 3}]
tooltip_list = [True, ["einrichtung"]]
name_list = [None, "Park(point)"]
style_list = [{}, {"fillOpacity": 0.7, "fillColor": "red", "color": "red"}]

In [50]:
map_viz = visualize_map(
    gdf_list=gdf_list,
    name_list=name_list,
    tooltip_list=tooltip_list,
    style_list=style_list,
    marker_style=marker_style,
)

map_viz

In [51]:
non_overlap_point = point_park_garden_dataset[
    ~point_park_garden_dataset["einrichtung"].isin(
        point_intersect_merged_dataset["einrichtung"].unique()
    )
]

There are only 3 points that aren't covered by the merged dataset (After filtering *zoo* out). Those points are
- Sportpark Ostragehege (It isn't covered because this point intersect with sport facilities area)
- Park Zwirnmühle (It isn't covered because this point intersect with area in F22-Large home gardens category)
- Park an der Haydnstraße (It isn't covered because this point intersect with area in F22-Large home gardens category)

However, when cross-check with the additional data and google street view, Park Zwirnmühle and Park an der Haydnstraße are public. So, they should be included in the dataset.

Check the polygons that overlap with non-overlap points

In [52]:
non_overlap_point_area = check_intersecting_point(
    non_overlap_point, green_os_dataset, buffer_distance=60
)

Points intersecting with dataset: 2 out of 3 (66.67%)


In [53]:
non_overlap_point_area = green_os_dataset.sjoin(
    non_overlap_point, how="inner", predicate="intersects"
)

In [54]:
gdf_list = [non_overlap_point_area]
name_list = ["Area of non-overlapping point"]

In [55]:
map_viz = visualize_map(gdf_list=gdf_list, name_list=name_list)

map_viz

From the above visualization, the area of Park Zwirnmühle is included in F11 - Allotments area. So, I will need to delineate the boundary of Park Zwirnmühle manually.

# 8. Check overlap and non-overlap area between dataset from Dresden and EUA

Two datasets are 
- Merged dataset (all datasets from Dresden)
- Dataset from EUA

These datasets are checked whether they has the overlapping and non-overlapping area or not and get some insight how they can complement each other.

## Hypothesis: Majority of the area should overlap with merged Dresden dataset

According to literature, Weigand et al. (2023) reclassified *Green urban areas*, *Forests*, and *Herbaceous vegetation association* as PUGS. So I expect that the **majority** of areas should overlap with merged Dresden dataset. It can have minor difference since these datasets has different data acquisition/creation time and rule to classify the area might be different in different dataset.

Reference: Weigand, M., Wurm, M., Droin, A., Stark, T., Staab, J., Rauh, J., & Taubenböck, H. (2023). Are public green spaces distributed fairly? A nationwide analysis based on remote sensing, OpenStreetMap and census data. Geocarto International, 38(1). https://doi.org/10.1080/10106049.2023.2286305

In [56]:
overlap_eua_merged_dataset = find_overlap_area(eua_pugs_dataset, final_merged_dataset)
overlap_merged_eua_dataset = find_overlap_area(final_merged_dataset, eua_pugs_dataset)

In [57]:
calculate_dataset_overlap(eua_pugs_dataset, final_merged_dataset)

Dataset 1 overlap percentage: 92.40%
Dataset 2 overlap percentage: 86.62%


92.4% of EUA dataset overlap with the datasets from Dresden and 86.62% of the datasets from Dresden overlap with EUA dataset.

So, only 7.6% of EUA dataset that do not overlap

## Check non-overlapping area of EUA dataset

In [58]:
non_overlap_eua_pugs_dataset = overlap_eua_merged_dataset[
    overlap_eua_merged_dataset["overlap"] == "no"
]

In [59]:
gdf_list = [non_overlap_eua_pugs_dataset]
name_list = ["Non-overlapping EUA Dataset"]
tile_list = ["Esri Satellite", "OSM"]

In [60]:
# map_viz = visualize_map(
#     gdf_list=gdf_list,
#     name_list=name_list,
#     tile_list=tile_list,
# )

# map_viz

In [61]:
non_overlap_eua_pugs_dataset = non_overlap_eua_pugs_dataset.rename(
    columns={
        "index_right": "eua_index",
        "area_left": "area",
    }
)

In [62]:
non_overlap_eua_pugs_dataset = non_overlap_eua_pugs_dataset.drop(
    columns=[
        "sst_lv_3_liste",
        "sst_lv_2_liste",
        "deskn1_liste",
        "flaeche",
        "dataset_source",
        "area_right",
        "id",
        "ort",
        "groesse",
        "oa",
        "overlap",
        "area",
        "overlap_pct",
        "raw_overlap_area",
        "comment",
    ]
)

In [63]:
check_non_overlap_eua_pugs_dataset = find_overlap_area(
    non_overlap_eua_pugs_dataset, green_os_dataset
)

In [64]:
calculate_dataset_overlap(non_overlap_eua_pugs_dataset, green_os_dataset)

Dataset 1 overlap percentage: 24.84%
Dataset 2 overlap percentage: 0.31%


In [65]:
category_overlap_df = calculate_category_overlap(
    check_non_overlap_eua_pugs_dataset, green_os_dataset
)
display(category_overlap_df)

,category,total_overlap_pct,max_overlap,avg_overlap
1,F21 Klein- und Wochenendgärten,78.21,100.00,55.40
2,F22 Große Hausgärten,67.06,98.36,47.81
0,F11 Kleingärten,30.76,84.43,23.28
3,F31 Verkehrsbegleitgrün,22.82,99.92,40.90


### Check non-green spaces in non-overlapping area of EUA dataset

In [66]:
sentinel2_raster_path = config["paths"]["clipped_image_path"]

In [67]:
non_overlap_eua_pugs_dataset_ndvi = add_ndvi_to_polygons(
    non_overlap_eua_pugs_dataset, raster_path=sentinel2_raster_path, ndvi_band_index=16
)

In [68]:
print_non_green_space_info(non_overlap_eua_pugs_dataset_ndvi, 0.3)

Area of polygons with NDVI <= 0.3:
Low NDVI value area: 72058.01 m² from 1336705.83 m² (5.39%)


The result is some non-overlapping areas (24.84% of non-overlapping area) in EUA dataset *overlap with non-public category* that are filterd out and some (5.39%) are not no longer be green space.

# Conclusion

I decided to merge all the datasets from Dresden Open data portal, as each datasets complement each others to provide full representation of PUGS in Dresden. When cross-checking with the Parks dataset (point), I found that the datasets from Dresden portal cover all the points in public area, so EUA dataset is not needed to help complement *park* area.

After checking the overlap percentage between merged dataset (all datasets from Dresden open data portal) and EUA dataset. 92.4% of EUA dataset overlap with merged dataset and non-overlapping area in EUA dataset contains the areas that:
- intersect with non-public area
- are no longer green
and EUA dataset refers to the year 2018, while datasets from Dresden portal are more recent. 

**Hence, I decided not to use EUA dataset to create the ground truth. Only datasets from Dresden portal will be used and the area of Park Zwirnmühle will be manually delineated since there is no polygon in official dataset that represent this area.**

---

# Additional: Check non-green spaces in final dataset

In [69]:
final_merged_dataset_ndvi = add_ndvi_to_polygons(
    final_merged_dataset, raster_path=sentinel2_raster_path, ndvi_band_index=16
)

In [70]:
print_non_green_space_info(final_merged_dataset_ndvi, 0.3)

Area of polygons with NDVI <= 0.3:
Low NDVI value area: 224353.67 m² from 94711516.55 m² (0.24%)


In [71]:
gdf_list = [final_merged_dataset_ndvi[final_merged_dataset_ndvi["ndvi_mean"] <= 0.3]]
name_list = ["Low NDVI value area in final dataset"]
style_list = [
    {
        "fillColor": "blue",
        "color": "black",
        "weight": 2,
        "fillOpacity": 0.4,
    }
]
tile_list = ["Esri Satellite", "OSM"]

In [72]:
map_viz = visualize_map(
    gdf_list=gdf_list,
    name_list=name_list,
    style_list=style_list,
    tile_list=tile_list,
)

map_viz